# CatBoost feature selection tutorial

[![Open In Colab](https://colab.research.google.com/assets/colab-badge.svg)](https://colab.research.google.com/github/catboost/tutorials/blob/master/feature_selection/eval_tutorial.ipynb)

## Library installation

Install required packages

* pip install catboost
* pip install plotly

In [3]:
import catboost
print catboost.__version__

0.11.2


In [4]:
from catboost import CatBoostClassifier, Pool
from catboost.eval.catboost_evaluation import *

### Import plotly to show plots in ipython notebook

In [6]:
from plotly.offline import iplot, init_notebook_mode
init_notebook_mode(connected=False)

## Reading the data

In [16]:
from catboost import datasets
from catboost.utils import create_cd
import os

train_df, _ = datasets.amazon()

dataset_dir = os.path.join('..', 'amazon')
if not os.path.exists(dataset_dir):
    os.makedirs(dataset_dir)

train_file = os.path.join(dataset_dir, 'train.csv')
description_file = os.path.join(dataset_dir, 'train.cd')

train_df.to_csv(train_file, header=False, index=False)

feature_names = dict()
for column, name in enumerate(train_df):
    if column == 0:
        continue
    feature_names[column] = name
    
create_cd(
    label=0, 
    cat_features=list(range(1, train_df.columns.shape[0])),
    feature_names=feature_names,
    output_path=os.path.join(dataset_dir, 'train.cd')
)
!cat $description_file

0	Label	
1	Categ	RESOURCE
2	Categ	MGR_ID
3	Categ	ROLE_ROLLUP_1
4	Categ	ROLE_ROLLUP_2
5	Categ	ROLE_DEPTNAME
6	Categ	ROLE_TITLE
7	Categ	ROLE_FAMILY_DESC
8	Categ	ROLE_FAMILY
9	Categ	ROLE_CODE


Pipeline for feature evaluation is pretty simple:
1. Choose fold size, this step is task-dependent. One should use fold size which will guarantee representative sample of general population.  We suggest to use at most 50% of dataset as fold size, because otherwise it'll be easier to overfit on all dataset. 
2. Estimation learning params for such fold size. If we have representative sample, this params should be consistent for different folds. For feature evaluation one doesn't not need to tune all params, just the main ones: learning rate and ensemble size.  
3. Train models on each fold and compute test metrics on rest dataset. For big dataset test fold could be much bigger than learn. Such datasets should provide more stable results.

Here we assume that we know optimal learning rate and ensemble size, later we'll show, how one can easily estimate this parameters and use this library for other tasks, like model comparison.

We will use fold_size 16000 and learning rate 0.03

In [17]:
fold_size = 16000
fold_offset = 0
folds_count = 20
random_seed = 0 

CatBoost supports custom group_column which could be used to split instances for learn/test folds.

CatboostEvaluation(group_column=id)

This column could be of any type in cd file (for example, auxilary)

In [18]:
learn_params = {'iterations': 2000, 
                'random_seed': 0, 
                'logging_level': 'Silent',
                'loss_function': 'Logloss',
                # You could set learning process to GPU
                # 'devices': '1',  
                # 'task_type': 'GPU',
                'loss_function' : 'Logloss',
                'boosting_type': 'Plain', 
                # For feature evaluation learning time is important and we need just the relative quality
                'max_ctr_complexity' : 4}

We will check quality of first 3 features

In [19]:
features_to_evaluate = [0, 1, 2]

### First we need to create evaluator object

In [20]:
from os.path import join
evaluator = CatboostEvaluation(train_file,
                               fold_size,
                               folds_count,
                               delimiter=',',
                               column_description=description_file,
                               partition_random_seed=random_seed,
                               #working_dir=...  — working directory, we will need to create temp files during evaluation, 
                               #so ensure you have enough free space. 
                               #By default we will create unique temp dir in system temp directory
                               #group_column=... — set it if you have column which should be used to split 
)

In [21]:
result = evaluator.eval_features(learn_config=learn_params,
                                 eval_metrics=["Logloss", "Accuracy"],
                                 features_to_eval=features_to_evaluate)

As a result we have instance of EvaluationResults object. 
To get results for one metric we need to call get_metric_results method

In [22]:
logloss_result = result.get_metric_results("Logloss")

Baseline case is pool without all tested features.
Test cases are EvalType dependent.
For SeqAdd mode we test pool with each feature added to pool, while other still ignored (forward selection):
So if we have SeqAdd mode for [0, 1, 2] features set, than test pools are:
1. Pool with all features except 0, 1
2. Pool with all features except 0, 2
3. Pool with all features except 1, 2

And baseline pool is pool without features 0, 1, 2

logloss_result is instance of MetricEvaluationResult class and contains all information about one metric
Usually we need to call just 3 method.
First one is get_baseline_comparision — create table with evaluation results

In [23]:
logloss_result.get_baseline_comparison()

,PValue,Score,Quantile 0.005,Quantile 0.995,Decision,Overfit iter diff,Overfit iter pValue
Features: 0,0.000089,6.691824,6.323326,7.094054,GOOD,584.0,0.000103
Features: 1,0.000089,4.154330,3.838582,4.443798,GOOD,21.6,0.822760
Features: 2,0.116888,-0.056478,-0.163765,0.083415,UNKNOWN,165.4,0.002495


In this table for each test case (Pool without some features) we show human-readable score (could be configured by  ScoreConfig param, by default we use (baseline_score - test_score) * magic_multiplier / baseline_score as score on one fold. Table score is mean score for all folds. Bigger score means bettter quality of this features).

Most important table entry: Decision. If there is UNKNOWN or BAD, than this feature doesn't not give any profit or we don't have enough data to see quality improvment from this feature.

If Deceision is good, than feature gives some profit. 

But be aware, that if overfit iter diff is big, than it could possible explanation for all profit you see

Second useful method — create_fold_learning_curve will create plotly plot on selected fold

In [24]:
iplot(logloss_result.create_fold_learning_curves(0))

In [25]:
baseline_case = logloss_result.get_baseline_case()

In [26]:
baseline_case

Features: None

In [27]:
baseline_result = logloss_result.get_case_result(baseline_case)

In [28]:
iplot(baseline_result.create_learning_curves_plot())

## Other tasks

### Choose learning rate

Now lets show, how to use library for other task.
For example, we could search for learning rate.
For this we just need to fit models with different learning rates and fixed ensemble size and look on learning curves

In [29]:
learning_rate_params = learn_params

In [30]:
baseline_case = ExecutionCase(label="Step {}".format(0.03),
                              params=learning_rate_params, 
                              learning_rate=0.03)

In [31]:
other_learning_rate_cases = [ExecutionCase(label="Step {}".format(step), 
                                           params=learning_rate_params, 
                                           learning_rate=step) for step in [0.05, 0.015]]

In [32]:
evaluator = CatboostEvaluation(train_file,
                               fold_size, 
                               fold_count=1,  #For learning rate estimation we need just 1 fold
                               delimiter=',',
                               column_description=description_file,
                               partition_random_seed=random_seed)

In [33]:
evaluator.get_working_dir()

'c:\\users\\annave~1\\appdata\\local\\temp\\tmp2sphnh'

In [34]:
learning_rates_result = evaluator.eval_cases(baseline_case, 
                                             other_learning_rate_cases,
                                             eval_metrics="Logloss")

Lets get results

In [35]:
logloss_learning_rate_search_results = learning_rates_result.get_metric_results("Logloss")

Let's see learning curves

In [36]:
tmp = logloss_learning_rate_search_results.create_fold_learning_curves(fold=0, offset=200)

In [37]:
iplot(tmp)

So default learning rate (0.03) seems good